# Chase Train Analytics
---

> Konstantinos Mpouros - MSc AI - University of Piraeus & NCSR "Demokritos"
> Xristos Karatsalos - MSc AI - University of Piraeus & NCSR "Demokritos"

This notebook contains analysis and visualizations specifically for the training episodes of the chase environment experiments. It includes rolling averages of capture rates and steps taken during training, segmented by different failure probabilities (`p_fail`). The goal is to understand how different training strategies and parameters affect the learning process of the agents involved in the chase game.

## Setup
Import libraries, paths, and helper utilities.


In [1]:
from pathlib import Path
import sys

import pandas as pd
import plotly.express as px
import plotly.graph_objects as go
from plotly.subplots import make_subplots

NOTEBOOK_DIR = Path(__file__).parent if '__file__' in globals() else Path.cwd()
PROJECT_ROOT = NOTEBOOK_DIR.parent
RESULTS_PATH = PROJECT_ROOT / 'results' / 'chase_train.xlsx'
ROLL_WINDOW = 400  # episodes for rolling averages

if str(NOTEBOOK_DIR) not in sys.path:
    sys.path.insert(0, str(NOTEBOOK_DIR))

from utils import *

pd.set_option('display.max_columns', 60)
pd.set_option('display.width', 140)

print(f'Notebook dir: {NOTEBOOK_DIR}')
print(f'Results file: {RESULTS_PATH}')

Notebook dir: c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook
Results file: C:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\results\chase_train.xlsx


## 1. Load data & list runs
Load all sheets (runs) from the Excel log.


In [2]:
sheets = load_runs(RESULTS_PATH)
print('Sheets found:')
for name, df in sheets.items():
    print(f'  {name}: {len(df):,} rows')

Sheets found:
  fp_vs_fp: 334,133 rows
  minimaxq_selfplay: 355,700 rows
  minimaxq_vs_fp: 564,818 rows


## 2. Quick peek (first sheet)
See the first few rows to remember the columns.


In [3]:
run_name = next(iter(sheets))
sheets[run_name].head()


,run,p_fail,env_size,env_t_max,env_step_penalty,env_seed,episode,step,env_t,sid,sid_next,catcher_x,catcher_y,runner_x,runner_y,catcher_action_id,runner_action_id,catcher_action,runner_action,catcher_x_next,catcher_y_next,runner_x_next,runner_y_next,reward,capture,done,c_fail,r_fail,value_estimate,epsilon,catcher_agent,runner_agent,opp_pi_catcher,opp_pi_runner
0,fp_vs_fp,0.1,5,30,0.01,0,1,1,1,452,326,3,3,0,2,2,3,DOWN,LEFT,2,3,0,1,-0.01,False,False,False,False,NaN,NaN,FP,FP,"[0.19999999995999998, 0.19999999995999998, 0.1...","[0.19999999995999998, 0.19999999995999998, 0.1..."
1,fp_vs_fp,0.1,5,30,0.01,0,1,2,2,326,300,2,3,0,1,3,3,LEFT,LEFT,2,2,0,0,-0.01,False,False,False,False,NaN,NaN,FP,FP,"[0.19999999995999998, 0.19999999995999998, 0.1...","[0.19999999995999998, 0.19999999995999998, 0.1..."
2,fp_vs_fp,0.1,5,30,0.01,0,1,3,3,300,175,2,2,0,0,2,3,DOWN,LEFT,1,2,0,0,-0.01,False,False,False,False,NaN,NaN,FP,FP,"[0.19999999995999998, 0.19999999995999998, 0.1...","[0.19999999995999998, 0.19999999995999998, 0.1..."
3,fp_vs_fp,0.1,5,30,0.01,0,1,4,4,175,150,1,2,0,0,3,2,LEFT,DOWN,1,1,0,0,-0.01,False,False,False,False,NaN,NaN,FP,FP,"[0.19999999995999998, 0.19999999995999998, 0.1...","[0.19999999995999998, 0.19999999995999998, 0.1..."
4,fp_vs_fp,0.1,5,30,0.01,0,1,5,5,150,25,1,1,0,0,2,3,DOWN,LEFT,0,1,0,0,-0.01,False,False,False,False,NaN,NaN,FP,FP,"[0.19999999995999998, 0.19999999995999998, 0.1...","[0.19999999995999998, 0.19999999995999998, 0.1..."


## 3. Combine & enrich
- Attach all sheets into a single step-level DataFrame.
- Add derived columns.
- Compute episode-level metrics and rolling averages.

In [4]:
steps_df = add_derived_columns(combine_runs(sheets))
ep_df = episode_metrics(steps_df)
summary_df = capture_rate_by_run(ep_df)
roll_df = rolling_episode_metrics(ep_df, window=ROLL_WINDOW)

print(f'Step rows total: {len(steps_df):,}')
print(f'Episode rows total: {len(ep_df):,}')
display(summary_df)


Step rows total: 1,254,651
Episode rows total: 60,000


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:146: FutureWarning: DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.
  return ep_df.groupby(["run", "p_fail"], group_keys=False).apply(_add_roll)


,run,p_fail,capture_rate,avg_steps,avg_return
0,fp_vs_fp,0.1,0.7304,18.2143,0.555561
1,fp_vs_fp,0.2,0.8512,15.1990,0.707722
2,minimaxq_selfplay,0.1,0.6730,18.7979,0.491751
3,minimaxq_selfplay,0.2,0.7573,16.7721,0.597152
4,minimaxq_vs_fp,0.1,0.1347,28.2105,-0.146058
5,minimaxq_vs_fp,0.2,0.1273,28.2713,-0.154140


## 4. Training History
Training history plots per run type:
- FP self-play
- MinimaxQ self-play
- MinimaxQ (catcher) vs FP (runner)

* Rolling capture rate and steps per episode for the FP self-play.

In [5]:
run_fp = 'fp_vs_fp'
fp_ep = ep_df.loc[ep_df['run'] == run_fp]
if fp_ep.empty:
    print('No data for FP vs FP')
else:
    display(summary_df.loc[summary_df['run'] == run_fp])
    plot_run_trends(fp_ep, run=run_fp, window=ROLL_WINDOW, title_prefix='FP vs FP')


,run,p_fail,capture_rate,avg_steps,avg_return
0,fp_vs_fp,0.1,0.7304,18.2143,0.555561
1,fp_vs_fp,0.2,0.8512,15.1990,0.707722


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:146: FutureWarning: DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.
  return ep_df.groupby(["run", "p_fail"], group_keys=False).apply(_add_roll)


* Rolling capture rate and steps per episode for MinimaxQ vs MinimaxQ.


In [6]:
run_mm = 'minimaxq_selfplay'
mm_ep = ep_df.loc[ep_df['run'] == run_mm]
if mm_ep.empty:
    print('No data for MinimaxQ self-play')
else:
    display(summary_df.loc[summary_df['run'] == run_mm])
    plot_run_trends(mm_ep, run=run_mm, window=ROLL_WINDOW, title_prefix='MinimaxQ self-play')


,run,p_fail,capture_rate,avg_steps,avg_return
2,minimaxq_selfplay,0.1,0.6730,18.7979,0.491751
3,minimaxq_selfplay,0.2,0.7573,16.7721,0.597152


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:146: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



* Rolling capture rate and steps per episode for the mixed matchup, MinimaxQ (catcher) vs FP (runner).


In [7]:
run_mix = 'minimaxq_vs_fp'
mix_ep = ep_df.loc[ep_df['run'] == run_mix]
if mix_ep.empty:
    print('No data for MinimaxQ vs FP')
else:
    display(summary_df.loc[summary_df['run'] == run_mix])
    plot_run_trends(mix_ep, run=run_mix, window=ROLL_WINDOW, title_prefix='MinimaxQ vs FP')


,run,p_fail,capture_rate,avg_steps,avg_return
4,minimaxq_vs_fp,0.1,0.1347,28.2105,-0.146058
5,minimaxq_vs_fp,0.2,0.1273,28.2713,-0.154140


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:146: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



## 5. Action drift over training
Rolling action mix (stacked area) per run and p_fail.


In [8]:
if steps_df.empty:
    print('No steps data for action drift.')
else:
    for run in steps_df['run'].unique():
        for pf in sorted(steps_df.loc[steps_df['run']==run, 'p_fail'].dropna().unique()):
            sub = steps_df.loc[(steps_df['run']==run) & (steps_df['p_fail']==pf)]
            mix_c = rolling_action_mix(sub, who='catcher', window=ROLL_WINDOW)
            title_c = f"{run} (catcher) action drift, p_fail={pf}"
            plot_action_drift(mix_c, title=title_c)
            mix_r = rolling_action_mix(sub, who='runner', window=ROLL_WINDOW)
            title_r = f"{run} (runner) action drift, p_fail={pf}"
            plot_action_drift(mix_r, title=title_r)
    print('Action drift plots generated per run/p_fail.')


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



...

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:166: FutureWarning:

The default of observed=False is deprecated and will be changed to True in a future version of pandas. Pass observed=False to retain current behavior or observed=True to adopt the future default and silence this warning.

c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:180: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



Action drift plots generated per run/p_fail.


## 6. Return quantiles over training
Rolling quantiles (10/50/90%) of episode return per run and p_fail.


In [9]:
if ep_df.empty:
    print('No episode data for quantiles.')
else:
    quant_df = rolling_return_quantiles(ep_df, window=ROLL_WINDOW, quantiles=(0.1,0.5,0.9))
    for run in quant_df['run'].unique():
        for pf in sorted(quant_df.loc[quant_df['run']==run, 'p_fail'].dropna().unique()):
            sub = quant_df.loc[(quant_df['run']==run) & (quant_df['p_fail']==pf)]
            if sub.empty:
                continue
            fig = px.line(
                sub,
                x='episode',
                y='value',
                color='quantile',
                title=f"{run} return quantiles (p_fail={pf})",
                labels={'episode': 'Episode', 'value': 'Return', 'quantile': 'Quantile'},
            )
            fig.update_layout(template='plotly_white')
            fig.show()
    print('Return quantile plots generated per run/p_fail.')


c:\Users\user\Desktop\MSc - AI\Εξάμηνο 1ο\Ευφυείς Πράκτορες και Πολυπρακτορικά Συστήματα\Assignment\chase\notebook\utils.py:213: FutureWarning:

DataFrameGroupBy.apply operated on the grouping columns. This behavior is deprecated, and in a future version of pandas the grouping columns will be excluded from the operation. Either pass `include_groups=False` to exclude the groupings or explicitly select the grouping columns after groupby to silence this warning.



Return quantile plots generated per run/p_fail.


## 7. State-space heatmaps
Visit density and capture locations (catcher & runner) per run and p_fail.


In [10]:
if steps_df.empty:
    print('No steps data for heatmaps.')
else:
    runs = steps_df['run'].unique()
    for run in runs:
        pfs = sorted(steps_df.loc[steps_df['run']==run, 'p_fail'].dropna().unique())
        for pf in pfs:
            plot_visit_heatmaps(steps_df, run=run, p_fail=pf)


## 8. Overall comparison across runs & p_fail
Combined view of all runs by p_fail.


In [11]:
if roll_df.empty:
    print('No data to compare.')
else:
    p_fails = sorted([pf for pf in roll_df['p_fail'].dropna().unique()])
    for pf in p_fails:
        pf_df = roll_df.loc[roll_df['p_fail'] == pf]
        if pf_df.empty:
            continue
        fig = make_subplots(
            rows=1,
            cols=2,
            shared_xaxes=True,
            subplot_titles=(f'p_fail={pf} – Rolling capture rate', f'p_fail={pf} – Rolling steps'),
        )
        for run in pf_df['run'].unique():
            sub = pf_df.loc[pf_df['run'] == run]
            fig.add_trace(
                go.Scatter(x=sub['episode'], y=sub['roll_capture_rate'], mode='lines', name=run),
                row=1,
                col=1,
            )
            fig.add_trace(
                go.Scatter(x=sub['episode'], y=sub['roll_steps'], mode='lines', name=run),
                row=1,
                col=2,
            )
        fig.update_yaxes(title_text='Capture rate', range=[0, 1], row=1, col=1)
        fig.update_yaxes(title_text='Steps', row=1, col=2)
        fig.update_xaxes(title_text='Episode', row=1, col=1)
        fig.update_xaxes(title_text='Episode', row=1, col=2)
        fig.update_layout(
            height=400,
            width=1000,
            legend_title_text=None,
            template='plotly_white',
            legend=dict(orientation='v', y=0.5, yanchor='middle', x=1.02),
            margin=dict(r=160),
        )
        fig.show()
    print('Capture/steps rolling curves plotted per p_fail. Summary table above shows averages.')


Capture/steps rolling curves plotted per p_fail. Summary table above shows averages.


## 9. Trajectory samples
Visualize example episodes to see how catcher/runner move. <br> 
We show shortest and longest capture episodes per run/p_fail, plus a few random captures.

In [12]:
if steps_df.empty:
    print('No steps data for trajectories.')
else:
    for run in steps_df['run'].unique():
        for pf in sorted(steps_df.loc[steps_df['run']==run, 'p_fail'].dropna().unique()):
            sub = steps_df[(steps_df['run']==run) & (steps_df['p_fail']==pf)]
            caps = ep_df[(ep_df['run']==run) & (ep_df['p_fail']==pf) & ep_df['captured']]
            if caps.empty:
                print(f'No captures for run={run}, p_fail={pf}')
                continue
            shortest = caps.nsmallest(2, 'steps')['episode'].tolist()
            longest = caps.nlargest(2, 'steps')['episode'].tolist()
            sampled = caps.sample(min(3, len(caps)), random_state=42)['episode'].tolist()
            episodes = sorted(set(shortest + longest + sampled))
            print(f"Run={run}, p_fail={pf} episodes -> shortest: {shortest}, longest: {longest}, sample: {sampled}")
            traj = episode_trajectories(sub, run=run, episodes=episodes)
            if traj.empty:
                print('  No trajectory data loaded.')
                continue
            fig = plot_positions(traj)
            if fig:
                fig.update_layout(title=f"Trajectories – {run}, p_fail={pf} (ep {episodes})")
    print('Trajectory samples plotted per run/p_fail (shortest, longest, random captures).')


Run=fp_vs_fp, p_fail=0.1 episodes -> shortest: [211, 294], longest: [27, 214], sample: [7055, 7480, 5305]


Run=fp_vs_fp, p_fail=0.2 episodes -> shortest: [67, 77], longest: [81, 83], sample: [5432, 2372, 9110]


Run=minimaxq_selfplay, p_fail=0.1 episodes -> shortest: [93, 106], longest: [30, 34], sample: [8142, 287, 9409]


Run=minimaxq_selfplay, p_fail=0.2 episodes -> shortest: [284, 327], longest: [161, 368], sample: [7971, 4534, 8554]


Run=minimaxq_vs_fp, p_fail=0.1 episodes -> shortest: [207, 412], longest: [1280, 1533], sample: [7820, 9048, 4881]


Run=minimaxq_vs_fp, p_fail=0.2 episodes -> shortest: [245, 455], longest: [911, 2344], sample: [1891, 9401, 3480]


Trajectory samples plotted per run/p_fail (shortest, longest, random captures).
